# Camada Silver — CineData Analytics

Este notebook realiza a limpeza, transformação, deduplicação, tratamento de tipos e enriquecimento dos dados da camada Bronze para a camada Silver na arquitetura Medalhão.

Boas práticas e regras de negócio aplicadas:
- Criação do schema `silver` caso não exista;
- Padronização dos nomes de colunas exclusivamente para o português;
- Deduplicação mantendo a versão mais recente com base na coluna `ingestion_datetime`;
- Normalização e tradução do status dos filmes com tratamento para dados corrompidos;
- Conversão robusta de datas com múltiplos formatos e extração do ano de lançamento;
- Higienização de moedas, conversão numérica segura e cálculo do financeiro em BRL;
- Prevenção de divisão por zero na margem de lucro e invalidação de inconsistências;
- Normalização de notas e métricas de engajamento (TMDB e IMDb) nos limites de negócio;
- Deduplicação de avaliações de usuários e tratamento de comentários em branco;
- Desmembramento (`explode`) de gêneros, atores, diretores, roteiristas e produtoras com limpeza de resíduos decorrentes de Column Shift;
- Preenchimento contínuo da cotação do dólar via técnica de *Forward Fill* (`last(..., ignorenulls=True)`).


In [0]:
# Imports utilizados no notebook
from pyspark.sql import functions as F
from pyspark.sql.window import Window

spark.table("bronze.tb_movies_info").printSchema()


root
 |-- id: integer (nullable = true)
 |-- tconst: string (nullable = true)
 |-- title: string (nullable = true)
 |-- original_title: string (nullable = true)
 |-- original_language: string (nullable = true)
 |-- release_date: string (nullable = true)
 |-- runtime: string (nullable = true)
 |-- status: string (nullable = true)
 |-- overview: string (nullable = true)
 |-- tagline: string (nullable = true)
 |-- ingestion_datetime: timestamp (nullable = true)



In [0]:
# Configuração dos schemas
bronze_schema = "bronze"
silver_schema = "silver"

# Cria o database da camada Silver caso ainda não exista
spark.sql(f"CREATE DATABASE IF NOT EXISTS {silver_schema}")

DataFrame[]

## 1. silver.tb_info_filmes

Transformação da tabela `bronze.tb_movies_info`.
Aplica renomeação de colunas, deduplicação pelo registro mais recente de ingestão, normalização e tradução do status, tratamento robusto de datas multi-formato e derivação da coluna `ano_lancamento`.


In [0]:
# Leitura da origem Bronze
df_info_raw = spark.table(f"{bronze_schema}.tb_movies_info")

# 1. Deduplicação: Mantém a versão mais recente com base no ingestion_datetime por id de filme
window_info = Window.partitionBy("id").orderBy(F.col("ingestion_datetime").desc())
df_info_dedup = (
    df_info_raw
    .withColumn("row_num", F.row_number().over(window_info))
    .filter(F.col("row_num") == 1)
    .drop("row_num")
)

# 2. Normalização e Limpeza da Coluna de Status antes da tradução
status_clean = F.lower(F.trim(F.regexp_replace(F.col("status"), "[^a-zA-Z ]", "")))

status_traduzido = (
    F.when(status_clean == "released", "Lançado")
    .when(status_clean == "post production", "Pós-Produção")
    .when(status_clean == "in production", "Em Produção")
    .when(status_clean == "planned", "Planejado")
    .when(status_clean == "rumored", "Rumores")
    .when(status_clean == "canceled", "Cancelado")
    .otherwise("Não Informado")
)

# 3. Tratamento de Data Multi-Formato
data_parseada = F.coalesce(
    F.expr("try_to_date(release_date, 'yyyy-MM-dd')"),
    F.expr("try_to_date(release_date, 'dd/MM/yyyy')"),
    F.expr("try_to_date(release_date, 'MM/dd/yyyy')"),
    F.expr("try_to_date(release_date, 'yyyy/MM/dd')")
)

# 4. Seleção e Mapeamento Final de Colunas
df_info_silver = (
    df_info_dedup
    .select(
        F.expr("try_cast(id as string)").alias("id_filme"),
        F.trim(F.col("title")).alias("titulo"),
        F.trim(F.col("original_title")).alias("titulo_original"),
        data_parseada.alias("data_lancamento"),
        F.year(data_parseada).cast("integer").alias("ano_lancamento"),
        F.expr("try_cast(runtime as int)").alias("duracao_minutos"),
        F.lower(F.trim(F.col("original_language"))).alias("idioma_original"),
        status_traduzido.alias("status_filme"),
        F.trim(F.col("overview")).alias("sinopse"),
        F.trim(F.col("tagline")).alias("frase_divulgacao")
    )
)

# Salvamento na camada Silver
(
    df_info_silver.write
    .format("delta")
    .mode("overwrite")
    .saveAsTable(f"{silver_schema}.tb_info_filmes")
)

print(f"Tabela {silver_schema}.tb_info_filmes criada com sucesso.")


Tabela silver.tb_info_filmes criada com sucesso.


## 2. silver.tb_cotacao_dolar

Tratamento das cotações obtidas da API do Banco Central.
Cria uma série temporal diária contínua e aplica Forward Fill (`last(..., ignorenulls=True)`) para preencher finais de semana e feriados com a última cotação útil disponível.


In [0]:
df_cotacao_raw = spark.table(f"{bronze_schema}.tb_cotacao_dolar")

# Extrai a data e obtém a cotação média/mais recente para cada dia presente na Bronze
df_cotacao_diaria = (
    df_cotacao_raw
    .withColumn("data_cotacao", F.to_date(F.col("dataHoraCotacao")))
    .groupBy("data_cotacao")
    .agg(F.avg("cotacaoCompra").cast("decimal(18,4)").alias("cotacao_usd_brl"))
)

# Identifica o intervalo de datas da base para gerar o calendário contínuo
datas_limite = df_cotacao_diaria.select(
    F.min("data_cotacao").alias("data_min"),
    F.max("data_cotacao").alias("data_max")
).collect()[0]

data_min = datas_limite["data_min"]
data_max = datas_limite["data_max"]

# Gera a sequência contínua de dias corridos
df_calendario = (
    spark.range(0, (data_max - data_min).days + 1)
    .select(F.expr(f"date_add(to_date('{data_min}'), cast(id as int))").alias("data_cotacao"))
)

# Aplica Forward Fill na cotação para preencher dias sem registro (finais de semana/feriados)
window_ffill = Window.orderBy("data_cotacao").rowsBetween(Window.unboundedPreceding, Window.currentRow)

df_cotacao_silver = (
    df_calendario
    .join(df_cotacao_diaria, "data_cotacao", "left")
    .withColumn("cotacao_usd_brl", F.last("cotacao_usd_brl", ignorenulls=True).over(window_ffill))
)

# Persiste a cotação tratada na Silver
(
    df_cotacao_silver.write
    .format("delta")
    .mode("overwrite")
    .saveAsTable(f"{silver_schema}.tb_cotacao_dolar")
)

print(f"Tabela {silver_schema}.tb_cotacao_dolar tratada com Forward Fill com sucesso.")


/databricks/python/lib/python3.12/site-packages/pyspark/sql/connect/expressions.py:1155: UserWarning: WARN WindowExpression: No Partition Defined for Window operation! Moving all data to a single partition, this can cause serious performance degradation.
  warnings.warn(


Tabela silver.tb_cotacao_dolar tratada com Forward Fill com sucesso.


## 3. silver.tb_financeiro_filmes

Transformação da tabela `bronze.tb_movies_financials`.
Higieniza textos e símbolos monetários, converte para decimal, cruza com a cotação do dólar para obter valores em BRL e deriva Lucro e Margem de Lucro Percentual.


In [0]:
df_fin_raw = spark.table(f"{bronze_schema}.tb_movies_financials")
df_info_silver = spark.table(f"{silver_schema}.tb_info_filmes").select("id_filme", "data_lancamento")
df_cotacao = spark.table(f"{silver_schema}.tb_cotacao_dolar")

# Deduplica os registros financeiros pelo mais recente
window_fin = Window.partitionBy("id").orderBy(F.col("ingestion_datetime").desc())
df_fin_dedup = (
    df_fin_raw
    .withColumn("row_num", F.row_number().over(window_fin))
    .filter(F.col("row_num") == 1)
    .drop("row_num")
)

# Função de limpeza para colunas monetárias em texto
def limpa_monetario(col_name):
    # Substitui textos de ausência por NULL, remove símbolos e formatação
    col_limpa = F.regexp_replace(F.col(col_name), r"(?i)unknown|não informado|n/a|\$", "")
    col_limpa = F.regexp_replace(col_limpa, r"[^\d.]", "")
    col_num = F.nullif(col_limpa, F.lit("")).cast("decimal(18,2)")
    # Garante que valores zerados ou negativos sejam convertidos em NULL
    return F.when(col_num > 0, col_num).otherwise(None)

df_fin_limpo = (
    df_fin_dedup
    .select(
        F.expr("try_cast(id as string)").alias("id_filme"),
        limpa_monetario("budget").alias("orcamento_usd"),
        limpa_monetario("revenue").alias("receita_usd")
    )
)

# Obtém a data de lançamento para buscar a cotação de BRL correspondente
df_fin_com_data = df_fin_limpo.join(df_info_silver, "id_filme", "left")

# Obtém a cotação mais recente do histórico como fallback caso a data do filme não exista na cotação
cotacao_fallback = df_cotacao.select(F.last("cotacao_usd_brl", ignorenulls=True)).collect()[0][0]

df_fin_convertido = (
    df_fin_com_data
    .join(df_cotacao, df_fin_com_data.data_lancamento == df_cotacao.data_cotacao, "left")
    .withColumn("taxa_cambio", F.coalesce(F.col("cotacao_usd_brl"), F.lit(cotacao_fallback)))
    .withColumn("orcamento_brl", F.round(F.col("orcamento_usd") * F.col("taxa_cambio"), 2))
    .withColumn("receita_brl", F.round(F.col("receita_usd") * F.col("taxa_cambio"), 2))
)

# Deriva Lucro e Margem de Lucro Percentual de forma segura
df_fin_final = (
    df_fin_convertido
    .withColumn("lucro_usd", F.col("receita_usd") - F.col("orcamento_usd"))
    .withColumn("lucro_brl", F.col("receita_brl") - F.col("orcamento_brl"))
    .withColumn(
        "margem_lucro_percentual",
        F.when(
            (F.col("receita_usd").isNotNull()) & (F.col("receita_usd") > 0),
            F.round((F.col("lucro_usd") / F.col("receita_usd")) * 100, 2)
        ).otherwise(None)
    )
    .select(
        "id_filme",
        "orcamento_usd",
        "receita_usd",
        "orcamento_brl",
        "receita_brl",
        "lucro_usd",
        "lucro_brl",
        "margem_lucro_percentual"
    )
)

(
    df_fin_final.write
    .format("delta")
    .mode("overwrite")
    .saveAsTable(f"{silver_schema}.tb_financeiro_filmes")
)

print(f"Tabela {silver_schema}.tb_financeiro_filmes criada com sucesso.")


Tabela silver.tb_financeiro_filmes criada com sucesso.


## 4. silver.tb_metricas_engajamento

Transformação da tabela `bronze.tb_movies_metrics`.
Trata ruídos numéricos, limpa o deslocamento de colunas (*Column Shift*), aplica tipagem segura e descarta notas fora da escala [0, 10] e contagens/popularidade negativas.


In [0]:
df_metrics_raw = spark.table(f"{bronze_schema}.tb_movies_metrics")

# Deduplica pelo registro mais recente
window_metrics = Window.partitionBy("id").orderBy(F.col("ingestion_datetime").desc())
df_metrics_dedup = (
    df_metrics_raw
    .withColumn("row_num", F.row_number().over(window_metrics))
    .filter(F.col("row_num") == 1)
    .drop("row_num")
)

# Função para casting seguro de métricas numéricas flutuantes e inteiras
def limpa_double(col_name):
    return F.expr(f"try_cast(nullif(regexp_replace(regexp_replace({col_name}, ',', '.'), '[^0-9.]', ''), '') as double)")

def limpa_int(col_name):
    val_limpo = F.regexp_replace(F.col(col_name), r"[^\d]", "")
    return F.nullif(val_limpo, F.lit("")).cast("integer")

# Aplicação das regras de negócio e validações de intervalo
pop_clean = limpa_double("popularity")
vote_tmdb_clean = limpa_double("vote_average")
qtd_tmdb_clean = limpa_int("vote_count")
vote_imdb_clean = limpa_double("averageRating")
qtd_imdb_clean = limpa_int("numVotes")

df_metrics_silver = (
    df_metrics_dedup
    .select(
        F.expr("try_cast(id as string)").alias("id_filme"),
        F.when(pop_clean >= 0, pop_clean).otherwise(None).alias("popularidade"),
        F.when((vote_tmdb_clean >= 0) & (vote_tmdb_clean <= 10), vote_tmdb_clean).otherwise(None).alias("nota_media_tmdb"),
        F.when(qtd_tmdb_clean >= 0, qtd_tmdb_clean).otherwise(None).alias("qtd_votos_tmdb"),
        F.when((vote_imdb_clean >= 0) & (vote_imdb_clean <= 10), vote_imdb_clean).otherwise(None).alias("nota_media_imdb"),
        F.when(qtd_imdb_clean >= 0, qtd_imdb_clean).otherwise(None).alias("qtd_votos_imdb")
    )
)

(
    df_metrics_silver.write
    .format("delta")
    .mode("overwrite")
    .saveAsTable(f"{silver_schema}.tb_metricas_engajamento")
)

print(f"Tabela {silver_schema}.tb_metricas_engajamento criada com sucesso.")


Tabela silver.tb_metricas_engajamento criada com sucesso.


## 5. silver.tb_avaliacoes_usuarios

Transformação da tabela `bronze.tb_movies_reviews`.
Remove duplicatas completas, valida notas no intervalo [0, 10] e preenche comentários vazios/com espaços com "Sem comentário".


In [0]:
df_reviews_raw = spark.table(f"{bronze_schema}.tb_movies_reviews")

# 1. Deduplicação integral (mesmo filme, usuário, nota e comentário)
df_reviews_dedup = df_reviews_raw.dropDuplicates(["id", "nome", "nota", "comentario"])

# 2. Limpeza e Validação de regras de negócio
nota_num = F.col("nota").cast("double")
comentario_trim = F.trim(F.col("comentario"))

df_reviews_silver = (
    df_reviews_dedup
    .select(
        F.col("id").cast("string").alias("id_filme"),
        F.trim(F.col("nome")).alias("nome_usuario"),
        F.when((nota_num >= 0) & (nota_num <= 10), nota_num).otherwise(None).alias("nota_usuario"),
        F.when((comentario_trim != "") & (comentario_trim.isNotNull()), comentario_trim)
         .otherwise("Sem comentário").alias("comentario_usuario")
    )
)

(
    df_reviews_silver.write
    .format("delta")
    .mode("overwrite")
    .saveAsTable(f"{silver_schema}.tb_avaliacoes_usuarios")
)

print(f"Tabela {silver_schema}.tb_avaliacoes_usuarios criada com sucesso.")


Tabela silver.tb_avaliacoes_usuarios criada com sucesso.


## 6. silver.tb_generos

Transformação da coluna `genres` de `bronze.tb_credits_and_tags`.
Padroniza separadores (vírgula e ponto e vírgula), realiza a explosão em múltiplos registros e filtra ruídos numéricos e residuais.


In [0]:
df_tags_raw = spark.table(f"{bronze_schema}.tb_credits_and_tags")

# Padroniza os delimitadores trocando ';' por ',' antes da explosão
df_generos_split = (
    df_tags_raw
    .select(
        F.col("id").cast("string").alias("id_filme"),
        F.explode(F.split(F.regexp_replace(F.col("genres"), ";", ","), ",")).alias("genero")
    )
)

# Limpa espaços, remove resíduos numéricos e registros inválidos por Column Shift
df_generos_clean = (
    df_generos_split
    .withColumn("genero_limpo", F.trim(F.col("genero")))
    .filter(
        (F.col("genero_limpo") != "") &
        (F.col("genero_limpo").isNotNull()) &
        (~F.col("genero_limpo").rlike(r"^\d+$"))
    )
    .select("id_filme", F.initcap(F.col("genero_limpo")).alias("nome_genero"))
    .distinct()
)

(
    df_generos_clean.write
    .format("delta")
    .mode("overwrite")
    .saveAsTable(f"{silver_schema}.tb_generos")
)

print(f"Tabela {silver_schema}.tb_generos criada com sucesso.")


Tabela silver.tb_generos criada com sucesso.


## 7. silver.tb_pessoas_empresas

Transformação unificada das colunas `cast`, `directors`, `writers` e `production_companies` de `bronze.tb_credits_and_tags`.
Consolida as quatro entidades em um único modelo com mapeamento de tipo, limpeza e capitalização padronizada.


In [0]:
df_tags_raw = spark.table(f"{bronze_schema}.tb_credits_and_tags")

# Função para processar e desmembrar colunas de entidades com separadores mistos
def processa_entidades(col_origem, tipo_entidade):
    return (
        df_tags_raw
        .select(
            F.col("id").cast("string").alias("id_filme"),
            F.explode(F.split(F.regexp_replace(F.col(col_origem), ";", ","), ",")).alias("nome_bruto")
        )
        .withColumn("nome_limpo", F.trim(F.col("nome_bruto")))
        .filter(
            (F.col("nome_limpo") != "") &
            (F.col("nome_limpo").isNotNull()) &
            (~F.col("nome_limpo").rlike(r"^\d+$"))
        )
        .select(
            "id_filme",
            F.initcap(F.col("nome_limpo")).alias("nome_entidade"),
            F.lit(tipo_entidade).alias("tipo_entidade")
        )
    )

# Desmembra cada papel/entidade
df_elenco = processa_entidades("cast", "Ator")
df_diretores = processa_entidades("directors", "Diretor")
df_roteiristas = processa_entidades("writers", "Roteirista")
df_produtoras = processa_entidades("production_companies", "Produtora")

# Consolida os DataFrames em uma única tabela Silver deduplicada
df_pessoas_empresas_silver = (
    df_elenco
    .unionByName(df_diretores)
    .unionByName(df_roteiristas)
    .unionByName(df_produtoras)
    .distinct()
)

(
    df_pessoas_empresas_silver.write
    .format("delta")
    .mode("overwrite")
    .saveAsTable(f"{silver_schema}.tb_pessoas_empresas")
)

print(f"Tabela {silver_schema}.tb_pessoas_empresas criada com sucesso.")


Tabela silver.tb_pessoas_empresas criada com sucesso.


## 8. Validação da Camada Silver

Exibe as primeiras linhas de cada tabela criada na camada Silver para validação da estrutura e dos dados.


In [0]:
# Lista de tabelas da camada Silver
tabelas_silver = [
    "tb_info_filmes",
    "tb_financeiro_filmes",
    "tb_metricas_engajamento",
    "tb_avaliacoes_usuarios",
    "tb_generos",
    "tb_pessoas_empresas",
    "tb_cotacao_dolar"
]

for tabela in tabelas_silver:
    print(f"===== {silver_schema}.{tabela} =====")
    display(
        spark.table(f"{silver_schema}.{tabela}")
    )


===== silver.tb_info_filmes =====


id_filme,titulo,titulo_original,data_lancamento,ano_lancamento,duracao_minutos,idioma_original,status_filme,sinopse,frase_divulgacao
14564,Rings,Rings,2017-02-01,2017,102,en,Lançado,"\Julia becomes worried about her boyfriend Holt when he explores the dark urban legend of a mysterious videotape said to kill the watcher seven days after viewing. She sacrifices herself to save her boyfriend and in doing so makes a horrifying discovery: there is a """"\""""movie within the movie""""\"""" that no one has ever seen before.""""""""First you watch it. Then you die.",null
32471,Mixtape,Mixtape,2021-12-03,2021,94,en,Lançado,null,null
38258,Grizzly II: Revenge,Grizzly II: Revenge,2020-02-17,2020,74,en,Lançado,\All hell breaks loose when a giant grizzly,reacting to the slaughter of her cubs by poachers
38492,Billy Joel - Live at Yankee Stadium,Billy Joel Live at Yankee Stadium,2022-06-22,2022,86,en,Lançado,Billy Joel plays his greatest hits in the Big Apple.,null
38700,Bad Boys for Life,Bad Boys for Life,2020-01-15,2020,124,en,Lançado,"Marcus and Mike are forced to confront new threats, career changes, and midlife crises as they join the newly created elite team AMMO of the Miami police department to take down the ruthless Armando Armas, the vicious leader of a Miami drug cartel.",Ride together. Die together.
42018,The Horse Thief,盗马贼,2019-03-19,2019,88,zh,Lançado,"Devout Buddhists, Norbu and Dolma live with their young son Tashi in a clan in Tibet. Norbu is a highwayman. After Norbu is charged with stealing from the temple, he and his family are banished. Impoverished and marginalized, they can do little when their beloved son becomes ill. Tashi dies of a fever. After a second son is born, Norbu focuses his every action on keeping this child alive, seeking re-admission to the clan for his wife and child, then risking all to save them from isolation and starvation in winter.",null
42330,Monkey Magic,大闹西游,2018-09-22,2018,66,zh,Lançado,"Dearth Voyd, the ruler of the dark side of the universe, wants to turn the human world into a place of violence and evil!! However, a huge meteor falls upon Flower-Fruit mountain giving birth to Kongo, a monkey made of stone! Kongo, now sets out on his quest to fight evil and restore order to a desperate land. Episodes 1-3",null
43074,Ghostbusters,Ghostbusters,2016-07-14,2016,117,en,Lançado,"Following a ghost invasion of Manhattan, paranormal enthusiasts Erin Gilbert and Abby Yates, nuclear engineer Jillian Holtzmann, and subway worker Patty Tolan band together to stop the otherworldly threat.",Who You Gonna Call?
45033,20 Seconds of Joy,20 Seconds of Joy,2018-01-01,2018,60,de,Lançado,"Traces the story of an extreme athlete, past and present; but also explores the psychology behind life, death, risk and the confrontation of fear.",null
46983,The Song of Styrene,Le Chant du styrène,2022-05-23,2022,13,fr,Lançado,Le chant du Styrène is a 1958 French documentary film directed by Alain Resnais. The film was an order by French industrial group Pechiney to highlight the merits of plastics.,null


===== silver.tb_financeiro_filmes =====


id_filme,orcamento_usd,receita_usd,orcamento_brl,receita_brl,lucro_usd,lucro_brl,margem_lucro_percentual
14564,25000000.00,83080890.00,124822500.00,414814575.68,58080890.00,289992075.68,69.91
32471,null,null,null,null,null,null,null
38258,7.50,null,37.45,null,null,null,null
38492,null,null,null,null,null,null,null
38700,90.00,426505244.00,449.36,2129498032.77,426505154.00,2129497583.41,100.00
42018,null,null,null,null,null,null,null
42330,null,null,null,null,null,null,null
43074,144000000.00,229147509.00,718977600.00,1144110597.69,85147509.00,425132997.69,37.16
45033,337200.00,null,1683605.88,null,null,null,null
46983,null,null,null,null,null,null,null


===== silver.tb_metricas_engajamento =====


...

id_filme,nome_genero
269149,Animation
429617,Science Fiction
330459,Action
127380,Family
332562,Romance
291805,Action
293167,Action
381284,History
454626,Action
454626,Science Fiction


===== silver.tb_pessoas_empresas =====


id_filme,nome_entidade,tipo_entidade
299536,Don Cheadle,Ator
263115,Hugh Jackman,Ator
354912,Anthony Gonzalez,Ator
419430,Daniel Kaluuya,Ator
424694,Mike Myers,Ator
374720,Mark Rylance,Ator
321612,Ewan Mcgregor,Ator
335983,Tom Hardy,Ator
363088,Evangeline Lilly,Ator
363088,Randall Park,Ator


===== silver.tb_cotacao_dolar =====


data_cotacao,cotacao_usd_brl
2026-09-30,5.1803
2026-10-01,5.2073
2026-10-02,5.2232
2026-10-03,5.2232
2026-10-04,5.2232
2026-10-05,4.9853
2026-10-06,4.9692
2026-10-07,4.9929
